In [0]:
display(dbutils.fs.ls("/Volumes/workspace/default/cinedata_inputs"))

path,name,size,modificationTime
dbfs:/Volumes/workspace/default/cinedata_inputs/credits_and_tags_IMDB_TMDB.csv,credits_and_tags_IMDB_TMDB.csv,22320678,1791404849000
dbfs:/Volumes/workspace/default/cinedata_inputs/movies_financials_IMDB_TMDB.csv,movies_financials_IMDB_TMDB.csv,1467743,1791404835000
dbfs:/Volumes/workspace/default/cinedata_inputs/movies_info_TMDB_IMDB.csv,movies_info_TMDB_IMDB.csv,33924063,1791404851000
dbfs:/Volumes/workspace/default/cinedata_inputs/movies_metrics_IMDB_TMDB.csv,movies_metrics_IMDB_TMDB.csv,3323884,1791404840000
dbfs:/Volumes/workspace/default/cinedata_inputs/movies_reviews.csv,movies_reviews.csv,1923431,1791404837000


In [0]:
%sql
CREATE SCHEMA IF NOT EXISTS bronze;

In [0]:
df_movies_info = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/cinedata_inputs/movies_info_TMDB_IMDB.csv")

display(df_movies_info)

id,tconst,title,original_title,original_language,release_date,runtime,status,overview,tagline
293660,tt1431045,Deadpool,Deadpool,en,2016-02-09,108,Released,"The origin story of former Special Forces operative turned mercenary Wade Wilson, who, after being subjected to a rogue experiment that leaves him with accelerated healing powers, adopts the alter ego Deadpool. Armed with his new abilities and a dark, twisted sense of humor, Deadpool hunts down the man who nearly destroyed his life.",Witness the beginning of a happy ending.
299536,tt4154756,AVENGERS: INFINITY WAR,Avengers: Infinity War,en,04-25-2018,149,Released,"As the Avengers and their allies have continued to protect the world from threats too large for any one hero to handle, a new danger has emerged from the cosmic shadows: Thanos. A despot of intergalactic infamy, his goal is to collect all six Infinity Stones, artifacts of unimaginable power, and use them to inflict his twisted will on all of reality. Everything the Avengers have fought for has led up to this moment - the fate of Earth and existence itself has never been more uncertain.",An entire universe. Once and for all.
299534,tt4154796,Avengers: Endgame,Avengers: Endgame,en,2019-04-24,181,released,"After the devastating events of Avengers: Infinity War, the universe is in ruins due to the efforts of the Mad Titan, Thanos. With the help of remaining allies, the Avengers must assemble once more in order to undo Thanos' actions and restore order to the universe once and for all, no matter what consequences may be in store.",Avenge the fallen.
475557,tt7286456,Joker,Joker,en,2019-10-01,122,Released,"During the 1980s, a failed stand-up comedian is driven insane and turns to a life of crime and chaos in Gotham City while becoming an infamous psychopathic crime figure.",Put on a happy face.
271110,tt3498820,Captain America: Civil War,Captain America: Civil War,en,2016-04-27,147,Released,"Following the events of Age of Ultron, the collective governments of the world pass an act designed to regulate all superhuman activity. This polarizes opinion amongst the Avengers, causing two factions to side with Iron Man or Captain America, which causes an epic battle between former allies.",United we stand. Divided we fall.
284054,tt1825683,Black Panther,Black Panther,en,2018-02-13,135,Released,"King T'Challa returns home to the reclusive, technologically advanced African nation of Wakanda to serve as his country's new leader. However, T'Challa soon finds that he is challenged for the throne by factions within his own country as well as without. Using powers reserved to Wakandan kings, T'Challa assumes the Black Panther mantle to join with ex-girlfriend Nakia, the queen-mother, his princess-kid sister, members of the Dora Milaje (the Wakandan 'special forces') and an American secret agent, to prevent Wakanda from being dragged into a world war.",null
284052,tt1211837,Doctor Strange,Doctor Strange,en,2016-10-25,115,Released,"After his career is destroyed, a brilliant but arrogant surgeon gets a new lease on life when a sorcerer takes him under her wing and trains him to defend the world against evil.",The impossibilities are endless.
315635,tt2250912,Spider-Man: Homecoming,Spider-Man: Homecoming,en,2017-07-05,133,RELEASED,"Following the events of Captain America: Civil War, Peter Parker, with the help of his mentor Tony Stark, tries to balance his life as an ordinary high school student in Queens, New York City, with fighting crime as his superhero alter ego Spider-Man as a new threat, the Vulture, emerges.",Homework can wait. The city can't.
283995,tt3896198,Guardians of the Galaxy Vol. 2,Guardians of the Galaxy Vol. 2,en,2017-04-19,137,Released,The Guardians must fight to keep their newfound family together as they unravel the mysteries of Peter Quill's true parentage.,Obviously.
297761,tt1386697,Suicide Squad,Suicide Squad,en,2016-08-03,123,Released,"From DC Comics comes the Suicide Squad, an antihero team of incarcerated sup

In [0]:
df_movies_info.printSchema()

root
 |-- id: integer (nullable = true)
 |-- tconst: string (nullable = true)
 |-- title: string (nullable = true)
 |-- original_title: string (nullable = true)
 |-- original_language: string (nullable = true)
 |-- release_date: string (nullable = true)
 |-- runtime: string (nullable = true)
 |-- status: string (nullable = true)
 |-- overview: string (nullable = true)
 |-- tagline: string (nullable = true)



In [0]:
from pyspark.sql.functions import current_timestamp

df_movies_info_bronze = df_movies_info.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_movies_info_bronze.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_movies_info")

In [0]:
%sql
SELECT *
FROM bronze.tb_movies_info
LIMIT 5;

id,tconst,title,original_title,original_language,release_date,runtime,status,overview,tagline,ingestion_datetime
293660,tt1431045,Deadpool,Deadpool,en,2016-02-09,108,Released,"The origin story of former Special Forces operative turned mercenary Wade Wilson, who, after being subjected to a rogue experiment that leaves him with accelerated healing powers, adopts the alter ego Deadpool. Armed with his new abilities and a dark, twisted sense of humor, Deadpool hunts down the man who nearly destroyed his life.",Witness the beginning of a happy ending.,2026-10-07T20:33:24.164Z
299536,tt4154756,AVENGERS: INFINITY WAR,Avengers: Infinity War,en,04-25-2018,149,Released,"As the Avengers and their allies have continued to protect the world from threats too large for any one hero to handle, a new danger has emerged from the cosmic shadows: Thanos. A despot of intergalactic infamy, his goal is to collect all six Infinity Stones, artifacts of unimaginable power, and use them to inflict his twisted will on all of reality. Everything the Avengers have fought for has led up to this moment - the fate of Earth and existence itself has never been more uncertain.",An entire universe. Once and for all.,2026-10-07T20:33:24.164Z
299534,tt4154796,Avengers: Endgame,Avengers: Endgame,en,2019-04-24,181,released,"After the devastating events of Avengers: Infinity War, the universe is in ruins due to the efforts of the Mad Titan, Thanos. With the help of remaining allies, the Avengers must assemble once more in order to undo Thanos' actions and restore order to the universe once and for all, no matter what consequences may be in store.",Avenge the fallen.,2026-10-07T20:33:24.164Z
475557,tt7286456,Joker,Joker,en,2019-10-01,122,Released,"During the 1980s, a failed stand-up comedian is driven insane and turns to a life of crime and chaos in Gotham City while becoming an infamous psychopathic crime figure.",Put on a happy face.,2026-10-07T20:33:24.164Z
271110,tt3498820,Captain America: Civil War,Captain America: Civil War,en,2016-04-27,147,Released,"Following the events of Age of Ultron, the collective governments of the world pass an act designed to regulate all superhuman activity. This polarizes opinion amongst the Avengers, causing two factions to side with Iron Man or Captain America, which causes an epic battle between former allies.",United we stand. Divided we fall.,2026-10-07T20:33:24.164Z


In [0]:
df_movies_financials = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/cinedata_inputs/movies_financials_IMDB_TMDB.csv")

display(df_movies_financials)

id,budget,revenue
293660,58000000,Unknown
299536,300000000,2052415039
299534,356000000,2800000000
475557,55000000,1074458282
271110,250000000,Não Informado
284054,200000000,1349926083
284052,180000000,676343174
315635,175000000,880166924
283995,200000000,863756051
297761,175000000,746846894


In [0]:
df_movies_financials.printSchema()

root
 |-- id: integer (nullable = true)
 |-- budget: string (nullable = true)
 |-- revenue: string (nullable = true)



In [0]:
from pyspark.sql.functions import current_timestamp

df_movies_financials_bronze = df_movies_financials.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_movies_financials_bronze.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_movies_financials")

In [0]:
%sql
SELECT *
FROM bronze.tb_movies_financials
LIMIT 5;

id,budget,revenue,ingestion_datetime
293660,58000000,Unknown,2026-10-07T20:35:20.670Z
299536,300000000,2052415039,2026-10-07T20:35:20.670Z
299534,356000000,2800000000,2026-10-07T20:35:20.670Z
475557,55000000,1074458282,2026-10-07T20:35:20.670Z
271110,250000000,Não Informado,2026-10-07T20:35:20.670Z


In [0]:
df_movies_metrics = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/cinedata_inputs/movies_metrics_IMDB_TMDB.csv")

display(df_movies_metrics)

id,popularity,vote_average,vote_count,averageRating,numVotes
293660,72.735,7.606,28894,8.0,1270339
299536,"154,34",8.255,27713,8.4,1406782
299534,91.756,8.263,23857,8.4,1484150
475557,"54,522",8.168,23425,8.3,1723035
271110,70.741,7.4,21541,7.8,947222
284054,43.665,7.39,null,7.3,924922
284052,70.535,7.427,20935,7.5,895880
315635,65.88,7.345,20507,7.4,835116
283995,67.553,7.624,20353,7.6,844767
297761,35.356,5.909,20097,5.9,null


In [0]:
df_movies_metrics.printSchema()

root
 |-- id: integer (nullable = true)
 |-- popularity: string (nullable = true)
 |-- vote_average: string (nullable = true)
 |-- vote_count: string (nullable = true)
 |-- averageRating: string (nullable = true)
 |-- numVotes: string (nullable = true)



In [0]:
from pyspark.sql.functions import current_timestamp

df_movies_metrics_bronze = df_movies_metrics.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_movies_metrics_bronze.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_movies_metrics")

In [0]:
%sql
SELECT *
FROM bronze.tb_movies_metrics
LIMIT 5;

id,popularity,vote_average,vote_count,averageRating,numVotes,ingestion_datetime
293660,72.735,7.606,28894,8.0,1270339,2026-10-07T20:36:39.960Z
299536,"154,34",8.255,27713,8.4,1406782,2026-10-07T20:36:39.960Z
299534,91.756,8.263,23857,8.4,1484150,2026-10-07T20:36:39.960Z
475557,"54,522",8.168,23425,8.3,1723035,2026-10-07T20:36:39.960Z
271110,70.741,7.4,21541,7.8,947222,2026-10-07T20:36:39.960Z


In [0]:
df_credits_tags = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/cinedata_inputs/credits_and_tags_IMDB_TMDB.csv")

display(df_credits_tags)

id,genres,production_companies,production_countries,spoken_languages,keywords,directors,writers,cast
293660,"Action, Adventure, Comedy","20th Century Fox, The Donners' Company, Genre Films",United States of America,English,"superhero, anti hero, mercenary, based on comic, aftercreditsstinger, duringcreditsstinger",Tim Miller,"Rhett Reese, Paul Wernick","Ryan Reynolds, Morena Baccarin, Ed Skrein, T.J. Miller, Gina Carano, Leslie Uggams, Brianna Hildebrand, Stefan Kapičić, Karan Soni, Randal Reeder"
299536,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"English, Xhosa","sacrifice, magic, superhero, based on comic, space, battlefield, genocide, magical object, super power, aftercreditsstinger, marvel cinematic universe (mcu), cosmic","Anthony Russo, Joe Russo",N/A,"Robert Downey Jr., Chris Evans, Chris Hemsworth, Josh Brolin, Mark Ruffalo, Scarlett Johansson, Don Cheadle, Benedict Cumberbatch, Tom Holland, Chadwick Boseman"
299534,"Adventure, Science Fiction, Action",Marvel Studios,United States of America,"English, Japanese, Xhosa","superhero, time travel, space travel, time machine, based on comic, sequel, alien invasion, superhero team, marvel cinematic universe (mcu), alternate timeline, father daughter relationship, sister sister relationship","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Stan Lee, Jack Kirby, Joe Simon, Steve Englehart, Steve Gan, Bill Mantlo, Keith Giffen, Jim Starlin, Larry Lieber, Don Heck","Robert Downey Jr., Chris Evans, Mark Ruffalo, Chris Hemsworth, Scarlett Johansson, Jeremy Renner, Josh Brolin, Don Cheadle, Paul Rudd, Benedict Cumberbatch"
475557,"Crime, Thriller, Drama","Warner Bros. Pictures, Joint Effort, Village Roadshow Pictures, Bron Studios, DC Films","Canada, United States of America",English,"dream, street gang, society, psychopath, clown, villain, based on comic, murder, psychological thriller, criminal mastermind, mental illness, anarchy, character study, clown makeup, subway train, social realism, supervillain, tv host, 1980s, mother son relationship, origin story, falling into madness, depressing",Todd Phillips,"Todd Phillips, Scott Silver, Bob Kane, Bill Finger, Jerry Robinson","Joaquin Phoenix, Robert De Niro, Zazie Beetz, Frances Conroy, Brett Cullen, Shea Whigham, Bill Camp, Glenn Fleshler, Leigh Gill, Josh Pais"
271110,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"Romanian, English, German, Russian","civil war, superhero, based on comic, sequel, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu), excited","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Joe Simon, Jack Kirby","Chris Evans, Robert Downey Jr., Scarlett Johansson, Sebastian Stan, Anthony Mackie, Don Cheadle, Jeremy Renner, Chadwick Boseman, Paul Bettany, Elizabeth Olsen"
284054,"Action, Adventure, Science Fiction",Marvel Studios,United States of America,"English, Korean, Swahili, Xhosa","africa, superhero, based on comic, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu)",Ryan Coogler,"Ryan Coogler, Joe Robert Cole, Stan Lee, Jack Kirby","Chadwick Boseman, Michael B. Jordan, Lupita Nyong'o, Danai Gurira, Martin Freeman, Daniel Kaluuya, Letitia Wright, Winston Duke, Sterling K. Brown, Angela Bassett"
284052,"Action, Adventure, Fantasy",Marvel Studios,UNITED STATES OF AMERICA,English,"magic, superhero, training, time, based on comic, sorcerer, doctor, neurosurgeon, wizard, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu)",Scott Derrickson,N/A,"Benedict Cumberbatch, Chiwetel Ejiofor, Rachel McAdams, Benedict Wong, Mads Mikkelsen, Tilda Swinton, Michael Stuhlbarg, Benjamin Bratt, Scott Adkins, Zara Phythian"
315635,"Action, Adventure, Science Fiction, Drama","Marvel Studios, Pascal Pictures, LStar Capital, Columbia Pictures",United States of America,English,"high school, new york city, washington dc, usa, superhero, based on comic, reboot, aftercredits

In [0]:
df_credits_tags.printSchema()

root
 |-- id: integer (nullable = true)
 |-- genres: string (nullable = true)
 |-- production_companies: string (nullable = true)
 |-- production_countries: string (nullable = true)
 |-- spoken_languages: string (nullable = true)
 |-- keywords: string (nullable = true)
 |-- directors: string (nullable = true)
 |-- writers: string (nullable = true)
 |-- cast: string (nullable = true)



In [0]:
from pyspark.sql.functions import current_timestamp

df_credits_tags_bronze = df_credits_tags.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_credits_tags_bronze.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_credits_and_tags")

In [0]:
%sql
SELECT *
FROM bronze.tb_credits_and_tags
LIMIT 5;

id,genres,production_companies,production_countries,spoken_languages,keywords,directors,writers,cast,ingestion_datetime
293660,"Action, Adventure, Comedy","20th Century Fox, The Donners' Company, Genre Films",United States of America,English,"superhero, anti hero, mercenary, based on comic, aftercreditsstinger, duringcreditsstinger",Tim Miller,"Rhett Reese, Paul Wernick","Ryan Reynolds, Morena Baccarin, Ed Skrein, T.J. Miller, Gina Carano, Leslie Uggams, Brianna Hildebrand, Stefan Kapičić, Karan Soni, Randal Reeder",2026-10-07T20:38:19.131Z
299536,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"English, Xhosa","sacrifice, magic, superhero, based on comic, space, battlefield, genocide, magical object, super power, aftercreditsstinger, marvel cinematic universe (mcu), cosmic","Anthony Russo, Joe Russo",N/A,"Robert Downey Jr., Chris Evans, Chris Hemsworth, Josh Brolin, Mark Ruffalo, Scarlett Johansson, Don Cheadle, Benedict Cumberbatch, Tom Holland, Chadwick Boseman",2026-10-07T20:38:19.131Z
299534,"Adventure, Science Fiction, Action",Marvel Studios,United States of America,"English, Japanese, Xhosa","superhero, time travel, space travel, time machine, based on comic, sequel, alien invasion, superhero team, marvel cinematic universe (mcu), alternate timeline, father daughter relationship, sister sister relationship","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Stan Lee, Jack Kirby, Joe Simon, Steve Englehart, Steve Gan, Bill Mantlo, Keith Giffen, Jim Starlin, Larry Lieber, Don Heck","Robert Downey Jr., Chris Evans, Mark Ruffalo, Chris Hemsworth, Scarlett Johansson, Jeremy Renner, Josh Brolin, Don Cheadle, Paul Rudd, Benedict Cumberbatch",2026-10-07T20:38:19.131Z
475557,"Crime, Thriller, Drama","Warner Bros. Pictures, Joint Effort, Village Roadshow Pictures, Bron Studios, DC Films","Canada, United States of America",English,"dream, street gang, society, psychopath, clown, villain, based on comic, murder, psychological thriller, criminal mastermind, mental illness, anarchy, character study, clown makeup, subway train, social realism, supervillain, tv host, 1980s, mother son relationship, origin story, falling into madness, depressing",Todd Phillips,"Todd Phillips, Scott Silver, Bob Kane, Bill Finger, Jerry Robinson","Joaquin Phoenix, Robert De Niro, Zazie Beetz, Frances Conroy, Brett Cullen, Shea Whigham, Bill Camp, Glenn Fleshler, Leigh Gill, Josh Pais",2026-10-07T20:38:19.131Z
271110,"Adventure, Action, Science Fiction",Marvel Studios,United States of America,"Romanian, English, German, Russian","civil war, superhero, based on comic, sequel, aftercreditsstinger, duringcreditsstinger, marvel cinematic universe (mcu), excited","Anthony Russo, Joe Russo","Christopher Markus, Stephen McFeely, Joe Simon, Jack Kirby","Chris Evans, Robert Downey Jr., Scarlett Johansson, Sebastian Stan, Anthony Mackie, Don Cheadle, Jeremy Renner, Chadwick Boseman, Paul Bettany, Elizabeth Olsen",2026-10-07T20:38:19.131Z


In [0]:
df_movies_reviews = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/cinedata_inputs/movies_reviews.csv")

display(df_movies_reviews)

id,nome,nota,comentario
442113,Mariana Cardoso 277,4.4,null
637007,Lucas Reis 602,3.9,null
449479,Sérgio Freitas,0.7,Péssimo em todos os sentidos.
413036,Gabriela Monteiro 401,7.5,null
528480,Leonardo Monteiro,6.3,Assisti até o final mas não me marcou.
387727,Maria Alves 707,8.2,"Gostei bastante, recomendo."
1032506,Amanda Castro 242,4.7,"Fraco, não recomendo."
446554,Sandra Rodrigues 736,6.5,Assisti até o final mas não me marcou.
569916,Camila Lima 489,8.2,Muito bom! Vale a pena assistir.
864552,Roberto Almeida 555,9.3,"Obra-prima do cinema, simplesmente espetacular."


In [0]:
df_movies_reviews.printSchema()

root
 |-- id: integer (nullable = true)
 |-- nome: string (nullable = true)
 |-- nota: double (nullable = true)
 |-- comentario: string (nullable = true)



In [0]:
from pyspark.sql.functions import current_timestamp

df_movies_reviews_bronze = df_movies_reviews.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_movies_reviews_bronze.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_movies_reviews")

In [0]:
%sql
SELECT *
FROM bronze.tb_movies_reviews
LIMIT 5;

id,nome,nota,comentario,ingestion_datetime
442113,Mariana Cardoso 277,4.4,null,2026-10-07T20:40:21.138Z
637007,Lucas Reis 602,3.9,null,2026-10-07T20:40:21.138Z
449479,Sérgio Freitas,0.7,Péssimo em todos os sentidos.,2026-10-07T20:40:21.138Z
413036,Gabriela Monteiro 401,7.5,null,2026-10-07T20:40:21.138Z
528480,Leonardo Monteiro,6.3,Assisti até o final mas não me marcou.,2026-10-07T20:40:21.138Z


In [0]:
dbutils.widgets.text("data_inicio", "10-01-2026", "Data inicial")
dbutils.widgets.text("data_fim", "10-07-2026", "Data final")

In [0]:
data_inicio = dbutils.widgets.get("data_inicio")
data_fim = dbutils.widgets.get("data_fim")

print("Data inicial:", data_inicio)
print("Data final:", data_fim)

Data inicial: 10-01-2026
Data final: 10-07-2026


In [0]:
df_reviews = (
    spark.read
    .option("header", True)
    .option("inferSchema", True)
    .csv("/Volumes/workspace/default/cinedata_inputs/movies_reviews.csv")
)

df_reviews = df_reviews.withColumn(
    "ingestion_datetime",
    current_timestamp()
)

df_reviews.write \
    .format("delta") \
    .mode("append") \
    .saveAsTable("bronze.tb_movies_reviews")

display(spark.table("bronze.tb_movies_reviews"))

id,nome,nota,comentario,ingestion_datetime
442113,Mariana Cardoso 277,4.4,null,2026-10-07T21:33:44.277Z
637007,Lucas Reis 602,3.9,null,2026-10-07T21:33:44.277Z
449479,Sérgio Freitas,0.7,Péssimo em todos os sentidos.,2026-10-07T21:33:44.277Z
413036,Gabriela Monteiro 401,7.5,null,2026-10-07T21:33:44.277Z
528480,Leonardo Monteiro,6.3,Assisti até o final mas não me marcou.,2026-10-07T21:33:44.277Z
387727,Maria Alves 707,8.2,"Gostei bastante, recomendo.",2026-10-07T21:33:44.277Z
1032506,Amanda Castro 242,4.7,"Fraco, não recomendo.",2026-10-07T21:33:44.277Z
446554,Sandra Rodrigues 736,6.5,Assisti até o final mas não me marcou.,2026-10-07T21:33:44.277Z
569916,Camila Lima 489,8.2,Muito bom! Vale a pena assistir.,2026-10-07T21:33:44.277Z
864552,Roberto Almeida 555,9.3,"Obra-prima do cinema, simplesmente espetacular.",2026-10-07T21:33:44.277Z


In [0]:
%sql
SHOW TABLES IN bronze;

database,tableName,isTemporary
bronze,tb_credits_and_tags,false
bronze,tb_movies_financials,false
bronze,tb_movies_info,false
bronze,tb_movies_metrics,false
bronze,tb_movies_reviews,false
